In [2]:
# we need numpy for the logarithm

import numpy as np 
import pandas as pd
import geopandas as gpd
import altair as alt

# Altair defaults to a 5,000-row limit; disable it since our dataset is larger
alt.data_transformers.disable_max_rows()

DataTransformerRegistry.enable('default')

In [8]:
df_StreetTree = pd.read_csv('/Users/michelle/Desktop/GIT/smt/data/original/2015_street_tree_census/2015_Street_Tree_Census_subset_um.csv')

# Preview the data
df_StreetTree.head()

,tree_id,block_id,created_at,tree_dbh,stump_diam,curb_loc,status,health,spc_latin,spc_common,...,boro_ct,state,latitude,longitude,x_sp,y_sp,council di,census tra,bin,bbl
0,198514,108318,09/02/2015,18,0,OnCurb,Alive,Good,Quercus palustris,pin oak,...,1019701,New York,40.802301,-73.962080,994748.4085,231579.2036,NaN,NaN,NaN,NaN
1,209919,108875,09/08/2015,9,0,OnCurb,Alive,Good,Platanus x acerifolia,London planetree,...,1020500,New York,40.808812,-73.963315,994405.4269,233951.0486,7.0,203.0,1084467.0,1.019730e+09
2,209921,108875,09/08/2015,3,0,OffsetFromCurb,Alive,Good,Platanus x acerifolia,London planetree,...,1020500,New York,40.808745,-73.963403,994380.9994,233926.6401,7.0,203.0,1084465.0,1.019730e+09
3,203887,108342,09/05/2015,5,0,OnCurb,Alive,Good,Quercus phellos,willow oak,...,1020101,New York,40.805726,-73.960719,995124.5475,232827.1256,7.0,20101.0,1056049.0,1.018670e+09
4,196440,108889,09/02/2015,5,0,OnCurb,Alive,Fair,Ulmus americana,American elm,...,1020500,New York,40.811145,-73.964123,994181.3574,234801.2532,7.0,205.0,1059835.0,1.019910e+09


In [9]:
# Count living trees, dead trees and stumps
print(df_StreetTree['status'].value_counts())

# Keep only the living trees. .copy() makes this a table of its own, so pandas doesn't warn when we change it
df_StreetTree = df_StreetTree[df_StreetTree['status'] == 'Alive'].copy()

status
Alive    12094
Dead       388
Stump      233
Name: count, dtype: int64


In [10]:
# Check the range of the diameter of the trees
print(df_StreetTree['tree_dbh'].describe())

# One record claims a 228-inch trunk. Treat anything over 60 inches as a data entry error.
df_StreetTree.loc[df_StreetTree['tree_dbh'] > 60, 'tree_dbh'] = np.nan

count    12094.000000
mean         8.927319
std          6.094538
min          1.000000
25%          5.000000
50%          8.000000
75%         11.000000
max        228.000000
Name: tree_dbh, dtype: float64


In [13]:
utd = pd.read_csv('/Users/michelle/Desktop/GIT/smt/data/original/queens_tree_equations.csv')
utd.head(10)

,SpCode,scientific_name,common_name,predicts,form,a,b,c,d,x_max,source
0,ACPL,Acer platanoides,Norway maple,age_from_dbh,cub,2.754430,0.28615,0.01875,-0.00013,114.66,"Urban Tree Database Table S6, Northeast (Queen..."
1,ACPL,Acer platanoides,Norway maple,crown_diameter_from_dbh,quad,1.057840,0.25365,-0.00083,NaN,NaN,"Urban Tree Database Table S6, Northeast (Queen..."
2,ACPL,Acer platanoides,Norway maple,dbh_from_age,lin,5.617050,0.91636,NaN,NaN,NaN,"Urban Tree Database Table S6, Northeast (Queen..."
3,ACPL,Acer platanoides,Norway maple,dry_weight_from_dbh_height,power,0.001011,1.53300,0.65700,520.00000,NaN,"Urban Tree Database Table 9, Acer platanoides;..."
4,ACPL,Acer platanoides,Norway maple,height_from_dbh,lin,3.168270,0.19507,NaN,NaN,NaN,"Urban Tree Database Table S6, Northeast (Queen..."
5,ACRU,Acer rubrum,red maple,age_from_dbh,cub,0.932440,0.02113,0.05658,-0.00055,105.20,"Urban Tree Database Table S6, Northeast (Queen..."
6,ACRU,Acer rubrum,red maple,crown_diameter_from_dbh,quad,0.207030,0.32103,-0.00152,NaN,NaN,"Urban Tree Database Table S6, Northeast (Queen..."
7,ACRU,Acer rubrum,red maple,dbh_from_age,cub,2.641660,1.27076,-0.01758,0.00012,NaN,"Urban Tree Database Table S6, Northeast (Queen..."
8,ACRU,Acer rubrum,red maple,dry_weight_from_dbh_height,power,0.197000,2.19330,0.00000,1.00000,NaN,"Urban Tree Database Table 10, Acer rubrum, dry..."
9,ACRU,Acer rubrum,red maple,height_from_dbh,quad,3.216980,0.24941,-0.00065,NaN,NaN,"Urban Tree Database Table S6, Northeast (Queen..."


In [14]:
# The 21 Queens species, by scientific name
species = dict(zip(utd['scientific_name'], utd['SpCode']))

# For a species that isn't one of the 21, the most common Queens species of the same genus 
same_genus = {'Acer': 'ACRU', 'Quercus': 'QUPA', 'Tilia': 'TICO', 'Ulmus': 'ULAM',
              'Prunus': 'PRSE2', 'Malus': 'MA2', 'Fraxinus': 'FRPE', 'Pinus': 'PIST'}

def match_species(latin):
    if pd.isna(latin):
        return 'GLTR'
    if latin in species:
        return species[latin]
    first_two = ' '.join(latin.split()[:2])   # 'Gleditsia triacanthos var. inermis' -> 'Gleditsia triacanthos'
    if first_two in species:
        return species[first_two]
    # Anything else is treated as a honeylocust (GLTR), the most common tree in the subset 
    return same_genus.get(latin.split()[0], 'GLTR')

df_StreetTree['SpCode'] = df_StreetTree['spc_latin'].map(match_species)
df_StreetTree['SpCode'].value_counts()

SpCode
GLTR     3735
QUPA     1396
PYCA     1309
PLAC     1061
GIBI     1004
TICO      868
ZESE      796
ULAM      617
QURU      273
PRSE2     215
FRPE      194
QUPH      132
ACRU      116
TITO      113
MA2        81
LIST       77
ACPL       76
ACSA2      16
ACSA1      10
PIST        4
AEHI        1
Name: count, dtype: int64

In [15]:
def equation(form, a, b, c, d, x):
    if form == 'lin':      return a + b*x
    if form == 'quad':     return a + b*x + c*x**2
    if form == 'cub':      return a + b*x + c*x**2 + d*x**3
    if form == 'loglogw1': return np.exp(a + b*np.log(np.log(x + 1) + c/2))
    if form == 'loglogw2': return np.exp(a + b*np.log(np.log(x + 1)) + np.sqrt(x)*c/2)
    if form == 'expow1':   return np.exp(a + b*x + c/2)

In [16]:
def predict(what, sp, x, height=None):
    out = np.full(len(x), np.nan)
    # This loops over the species, since each species has its own coefficients
    for code in np.unique(sp):
        # This is the one row of the equations file for this species and this equation
        row = utd[(utd['SpCode'] == code) & (utd['predicts'] == what)].iloc[0]
        i = (sp == code)
        # This caps the input at x_max, the largest tree the equation is meant for
        xi = x[i] if pd.isna(row['x_max']) else np.minimum(x[i], row['x_max'])
        if what == 'dry_weight_from_dbh_height':
            # This estimates wood volume from diameter and height, times the wood's density (d)
            out[i] = row['a'] * xi**row['b'] * height[i]**row['c'] * row['d']
        else:
            # This is every other equation, using the forms in equation() above
            out[i] = equation(row['form'], row['a'], row['b'], row['c'], row['d'], xi)
    return out

In [17]:
rain_m = 41.0 * 0.0254          # JFK airport, 2000 (Northeast Community Tree Guide, p. 100)
interception_fraction = 0.15    # a Callery pear in Davis, CA (Xiao et al. 2000)

def stormwater_gal_yr(sp, dbh_cm):
    # Crown diameter (m) from trunk diameter (cm). Very small trees can come out below zero; count those as zero.
    crown_m = np.maximum(predict('crown_diameter_from_dbh', sp, dbh_cm), 0)
    # Crown projection area (m²), modeled as a circle
    crown_area_m2 = np.pi * (crown_m / 2) ** 2
    # Rain over the crown (m³) x the share the crown catches, in gallons (1 m³ = 264.17 gallons)
    return crown_area_m2 * rain_m * interception_fraction * 264.17

sp = df_StreetTree['SpCode'].to_numpy()
dbh_cm = df_StreetTree['tree_dbh'].to_numpy() * 2.54

df_StreetTree['stormwater_gal_yr'] = stormwater_gal_yr(sp, dbh_cm)

print(f"Total stormwater intercepted per year: {df_StreetTree['stormwater_gal_yr'].sum():,.0f} gallons")
print(f"Median per-tree interception: {df_StreetTree['stormwater_gal_yr'].median():,.0f} gal/yr")

Total stormwater intercepted per year: 24,965,850 gallons
Median per-tree interception: 1,452 gal/yr


In [18]:
def co2_stored_kg(sp, dbh_cm):
    height_m = predict('height_from_dbh', sp, dbh_cm)
    dry_weight_kg = predict('dry_weight_from_dbh_height', sp, dbh_cm, height_m)
    return dry_weight_kg * 1.28 * 0.5 * 3.67   # roots, carbon, CO2 (Urban Tree Database, p. 73)

def grow_one_year(sp, dbh_cm, age):
    # How much a tree of this species and age thickens in a year. Past the end of the curve, it stops.
    step = predict('dbh_from_age', sp, age + 1) - predict('dbh_from_age', sp, age)
    return dbh_cm + np.maximum(step, 0)

age = np.maximum(predict('age_from_dbh', sp, dbh_cm), 0)
df_StreetTree['age'] = age
df_StreetTree['co2_seq_kg_yr'] = co2_stored_kg(sp, grow_one_year(sp, dbh_cm, age)) - co2_stored_kg(sp, dbh_cm)

# Dollar value: $0.00334 per pound of CO2 (Northeast Community Tree Guide, Table 18)
# To try another price, swap it in for 0.00334:
#   $0.0231 per pound of CO2 ($51 a metric ton, Biden admin, 2021)
#   $0.0862 per pound of CO2 ($190 a metric ton, EPA, 2023)
df_StreetTree['co2_value_usd'] = df_StreetTree['co2_seq_kg_yr'] * 2.2046 * 0.00334

print(f"Total CO₂ sequestered per year: {df_StreetTree['co2_seq_kg_yr'].sum():,.0f} kg")
print(f"Total CO₂ value per year: ${df_StreetTree['co2_value_usd'].sum():,.0f}")
print(f"Median per-tree sequestration: {df_StreetTree['co2_seq_kg_yr'].median():.1f} kg CO₂/yr")

Total CO₂ sequestered per year: 739,922 kg
Total CO₂ value per year: $5,448
Median per-tree sequestration: 60.4 kg CO₂/yr


In [19]:
chart_StreetTree_Storm = alt.Chart(df_StreetTree).mark_circle().encode(
    longitude='longitude:Q',
    latitude='latitude:Q',
    color=alt.Color(
        'stormwater_gal_yr:Q',
        scale=alt.Scale(scheme='blues'),
        legend=alt.Legend(title='Stormwater (gal/yr)')
    ),
    size=alt.Size(
        'tree_dbh:Q',
        scale=alt.Scale(range=[0, 228]),
        legend=alt.Legend(title='DBH (inches)')
    ),
    tooltip=[
        alt.Tooltip('spc_common:N', title='Species'),
        alt.Tooltip('SpCode:N', title='Equations used'),
        alt.Tooltip('tree_dbh:Q', title='DBH (in)', format='.1f'),
        alt.Tooltip('stormwater_gal_yr:Q', title='Stormwater (gal/yr)', format=',.0f'),
        alt.Tooltip('co2_seq_kg_yr:Q', title='CO₂ sequestered (kg/yr)', format='.1f')
    ]
).project(
    type='mercator'
).properties(
    width=700,
    height=700,
    title='Individual Trees: Annual Stormwater Interception'
)

chart_StreetTree_Storm

alt.Chart(...)

In [20]:
# Load blocks. Same file and reprojection as Tutorial 2
gdf_Blocks = gpd.read_file('/Users/michelle/Desktop/GIT/smt/data/original/nycb2010_subset_um/nycb2010_um.gpkg').to_crs(epsg=4326)

gdf_Blocks.head()

,CB2010,BoroCode,BoroName,CT2010,BCTCB2010,Shape_Leng,Shape_Area,geometry
0,1000,1,Manhattan,016800,10168001000,2106.253246,276994.092837,"MULTIPOLYGON (((-73.9479 40.79293, -73.94839 4..."
1,1000,1,Manhattan,017800,10178001000,1947.634689,186115.350370,"MULTIPOLYGON (((-73.93174 40.79699, -73.9322 4..."
2,1000,1,Manhattan,018000,10180001000,2059.932028,189842.926889,"MULTIPOLYGON (((-73.93591 40.79531, -73.93595 ..."
3,1000,1,Manhattan,018200,10182001000,1583.485495,143623.768522,"MULTIPOLYGON (((-73.94113 40.7993, -73.94162 4..."
4,1000,1,Manhattan,018400,10184001000,1550.256558,134355.161142,"MULTIPOLYGON (((-73.94181 40.80124, -73.94227 ..."


In [21]:
# Convert df_StreetTree to a GeoDataFrame. Same pattern as Tutorial 2
gdf_StreetTree = gpd.GeoDataFrame(
    df_StreetTree,
    geometry=gpd.points_from_xy(df_StreetTree['longitude'], df_StreetTree['latitude']),
    crs='EPSG:4326'
)

# Spatial join: attach block ID to each tree row
gdf_joined = gpd.sjoin(gdf_Blocks, gdf_StreetTree, how='right', predicate='contains')

# Aggregate per block: count trees, sum benefits
gdf_agg = gdf_joined.groupby('BCTCB2010').agg(
    tree_count=('tree_id', 'count'),
    total_stormwater_gal=('stormwater_gal_yr', 'sum'),
    total_co2_kg=('co2_seq_kg_yr', 'sum')
).reset_index()

# Average stormwater per tree. Shows where individual trees are working hardest,
# independent of how many trees a block has
gdf_agg['stormwater_per_tree'] = gdf_agg['total_stormwater_gal'] / gdf_agg['tree_count']

# Merge aggregated values back to the block GeoDataFrame
gdf_BenefitBlocks = gdf_Blocks.merge(gdf_agg, on='BCTCB2010', how='left')

# Fill blocks with no trees with 0 rather than NaN
gdf_BenefitBlocks[['tree_count', 'total_stormwater_gal', 'total_co2_kg', 'stormwater_per_tree']] = (
    gdf_BenefitBlocks[['tree_count', 'total_stormwater_gal', 'total_co2_kg', 'stormwater_per_tree']]
    .fillna(0)
)

print(f"Blocks with at least one tree: {(gdf_BenefitBlocks['tree_count'] > 0).sum()}")
print(f"Total blocks: {len(gdf_BenefitBlocks)}")
gdf_BenefitBlocks[['BCTCB2010', 'tree_count', 'total_stormwater_gal', 'total_co2_kg', 'stormwater_per_tree']].head(10)


Blocks with at least one tree: 480
Total blocks: 580


,BCTCB2010,tree_count,total_stormwater_gal,total_co2_kg,stormwater_per_tree
0,10168001000,9.0,8867.660607,165.349692,985.295623
1,10178001000,31.0,50452.798712,1561.048152,1627.509636
2,10180001000,11.0,9387.855421,423.988945,853.441402
3,10182001000,22.0,38541.776393,984.758675,1751.898927
4,10184001000,34.0,65238.434581,2399.134068,1918.777488
5,10186001000,0.0,0.000000,0.000000,0.000000
6,10190001000,53.0,87266.558468,2846.706651,1646.538839
7,10191001000,12.0,40580.353788,1123.164367,3381.696149
8,10195001000,43.0,57902.560995,1955.113444,1346.571186
9,10196001000,17.0,19711.353348,934.132512,1159.491373


In [23]:
# Shared base chart properties
base = alt.Chart(gdf_BenefitBlocks).mark_geoshape(
    stroke='black',
    strokeWidth=0.3
).project(
    type='mercator'
).properties(
    width=450,
    height=550
)

# Chart 1: Total stormwater benefit per block (blue)
chart_Stormwater = base.encode(
    color=alt.Color(
        'total_stormwater_gal:Q',
        scale=alt.Scale(scheme='blues'),
        legend=alt.Legend(title='Total Stormwater (gal/yr)')
    ),
    tooltip=[
        alt.Tooltip('BCTCB2010:N', title='Block'),
        alt.Tooltip('tree_count:Q', title='Tree Count'),
        alt.Tooltip('total_stormwater_gal:Q', title='Stormwater (gal/yr)', format=',.0f')
    ]
).properties(
    title='Total Stormwater Benefit'
)

# Chart 2: Total CO₂ sequestered per block (green)
chart_CO2 = base.encode(
    color=alt.Color(
        'total_co2_kg:Q',
        scale=alt.Scale(scheme='greens'),
        legend=alt.Legend(title='Total CO₂ (kg/yr)')
    ),
    tooltip=[
        alt.Tooltip('BCTCB2010:N', title='Block'),
        alt.Tooltip('tree_count:Q', title='Tree Count'),
        alt.Tooltip('total_co2_kg:Q', title='CO₂ (kg/yr)', format=',.0f')
    ]
).properties(
    title='Total CO₂ Sequestered'
)

# Chart 3: Stormwater per tree. Where individual trees are working hardest
chart_StormPerTree = base.encode(
    color=alt.Color(
        'stormwater_per_tree:Q',
        scale=alt.Scale(scheme='teals'),
        legend=alt.Legend(title='Stormwater per Tree (gal/yr)')
    ),
    tooltip=[
        alt.Tooltip('BCTCB2010:N', title='Block'),
        alt.Tooltip('tree_count:Q', title='Tree Count'),
        alt.Tooltip('stormwater_per_tree:Q', title='Stormwater per Tree (gal/yr)', format=',.0f')
    ]
).properties(
    title='Stormwater per Tree'
)

(chart_Stormwater | chart_CO2 | chart_StormPerTree).resolve_scale(color='independent')

alt.HConcatChart(...)

In [24]:
def run(df, years=range(2015, 2046), mortality=True):
    sp = df['SpCode'].to_numpy()
    dbh_cm = df['tree_dbh'].to_numpy() * 2.54
    age = np.maximum(predict('age_from_dbh', sp, dbh_cm), 0)
    standing = np.where(np.isnan(dbh_cm), 0.0, 1.0)   # the share of each tree still standing
    rows = []
    for year in years:
        gal = stormwater_gal_yr(sp, dbh_cm)
        rows.append({'year': year, 'trees': standing.sum(), 'stormwater_gal': np.nansum(standing * gal)})
        if mortality:
            # 2.8% a year for trees under 5 years old, 0.57% after (Northeast Community Tree Guide, p. 94)
            standing = standing * np.where(age < 5, 1 - 0.028, 1 - 0.0057)
        dbh_cm = grow_one_year(sp, dbh_cm, age)
        age = age + 1
    return pd.DataFrame(rows)

In [25]:
baseline = run(df_StreetTree)
baseline.tail()

,year,trees,stormwater_gal
26,2041,10377.733559,5.847908e+07
27,2042,10318.580477,5.959001e+07
28,2043,10259.764569,6.069221e+07
29,2044,10201.283911,6.178617e+07
30,2045,10143.136592,6.287239e+07


In [26]:
no_deaths = run(df_StreetTree, mortality=False)

baseline['scenario'] = 'Northeast guide mortality'
no_deaths['scenario'] = 'no trees die'
runs = pd.concat([baseline, no_deaths])

alt.Chart(runs).mark_line().encode(
    x='year:O',
    y=alt.Y('stormwater_gal:Q', title='Stormwater intercepted (gal/yr)'),
    color='scenario:N'
).properties(width=600, height=300, title='Two runs, one changed value')

alt.Chart(...)

In [27]:
# Each tree's stormwater and age in every year, 2015-2045, if it survives
sp = df_StreetTree['SpCode'].to_numpy()
dbh_cm = df_StreetTree['tree_dbh'].to_numpy() * 2.54
age = np.maximum(predict('age_from_dbh', sp, dbh_cm), 0)
gal_by_year, age_by_year = [], []
for year in range(2015, 2046):
    gal_by_year.append(stormwater_gal_yr(sp, dbh_cm))
    age_by_year.append(age)
    dbh_cm = grow_one_year(sp, dbh_cm, age)
    age = age + 1
gal_by_year = np.array(gal_by_year)
age_by_year = np.array(age_by_year)

In [28]:
def run_random(seed, which=None):
    rng = np.random.default_rng(seed)
    alive = ~np.isnan(gal_by_year[0])
    if which is not None:
        alive = alive & which
    totals = []
    for t in range(len(gal_by_year)):
        totals.append(np.nansum(gal_by_year[t][alive]))
        death_rate = np.where(age_by_year[t] < 5, 0.028, 0.0057)
        alive = alive & (rng.random(len(alive)) >= death_rate)
    return totals

years = list(range(2015, 2046))
random_runs = pd.DataFrame([run_random(seed) for seed in range(100)], columns=years)

band = pd.DataFrame({
    'year': years,
    'low': random_runs.quantile(0.05).to_numpy(),
    'high': random_runs.quantile(0.95).to_numpy(),
})

chart_Band = alt.Chart(band).mark_area(opacity=0.3).encode(
    x='year:O',
    y=alt.Y('low:Q', title='Stormwater intercepted (gal/yr)'),
    y2='high:Q'
)
chart_Average = alt.Chart(baseline).mark_line(color='black').encode(x='year:O', y='stormwater_gal:Q')

(chart_Band + chart_Average).properties(width=600, height=300, title='100 random runs and the average run')

alt.LayerChart(...)

In [29]:
# The block each tree is in, from the spatial join in Step 7.
tree_block = gdf_joined['BCTCB2010'].groupby(level=0).first().reindex(df_StreetTree.index).to_numpy()

# A filter to narrow down the trees to just one block.
one_block = (tree_block == '10242001004')

# 100 random runs that total only this block's trees. 
block_runs = pd.DataFrame([run_random(seed, which=one_block) for seed in range(100)], columns=years)

# The spread of the 100 runs in 2045: the lowest, the 5th, 50th and 95th percentiles, and the highest
print(block_runs[2045].describe(percentiles=[0.05, 0.5, 0.95]))

# Altair wants one row per run per year, so turn the wide table into a long one
block_long = block_runs.reset_index(names='run').melt(id_vars='run', var_name='year', value_name='stormwater_gal')

# One faint line per run. detail='run:N' draws a separate line for each run without giving each its own color
chart_BlockRuns = alt.Chart(block_long).mark_line(opacity=0.15).encode(
    x='year:O',
    y=alt.Y('stormwater_gal:Q', title='Stormwater intercepted (gal/yr)'),
    detail='run:N'
).properties(width=600, height=300, title='One block, 100 random runs')

chart_BlockRuns

count      100.000000
mean     65684.707350
std       8843.076139
min      40209.403301
5%       48668.037686
50%      67408.324348
95%      77680.190647
max      77680.190647
Name: 2045, dtype: float64


alt.Chart(...)